# Wilson-Cowan - ottobre 2026 (solo $h = 10^{-6}$)

Notebook per il modello di Wilson-Cowan sbilanciato (Nandi et al., *Phys. Rev. E* **107**, 064307 (2023)), con $\chi_E = 70\%$, $\chi_I = 30\%$, **solo per $h = 10^{-6}$** (il valore usato nell'articolo), sulla griglia dei parametri $(\delta_{IE}, \delta_{EI})$.

Contiene, nell'ordine: $E_0, I_0, \Sigma_0, \Delta_0$; correlazioni e risposte in un punto scelto; diagramma degli autovalori (Fig. 2 del paper); tasso di produzione di entropia $W$ (contour, **scatter in scala logaritmica**, linee); fluttuazione relativa; diagnostica del collasso a 1D nel primo quadrante.

**Convenzione sui dati.** Tutti i campi vengono caricati dal file `_sigmaFIX.npz` (covarianza $\sigma$ gia' corretta) e arrotondati a `DECIMALI = 9` cifre decimali: valori sotto $10^{-9}$ sono considerati zero, per coerenza con il lavoro di Manoj/Dario. 

**Modifiche rispetto alla versione precedente**
- Solo $h=10^{-6}$; layout dei grafici adattato a un solo pannello. Rimossi il confronto tra $h$ diversi e la diagnostica dell'arrotondamento su piu' $h$.
- Mascherata la regione proibita ($w_{EI}<0$ o $w_{IE}<0$, cioe' $\delta_{EI} = -7.0, -6.9$).
- $W$: separati esplicitamente i punti $0/0$ (primo quadrante, sistema 1D, equilibrio) dall'unico punto con $\delta^2/0 = \infty$, che e' un artefatto numerico sul bordo del primo quadrante (vedi Sez. 6 e Sez. 8).
- **$\beta_{eff}$ e la sua analisi spostati nel notebook `beta_ottobre.ipynb`** (prima: Sez. 7 e 8). Le sezioni successive sono rinumerate (9 -> 7, 10 -> 8).
- Correlazioni con opzione di normalizzazione $C(t)/C(0)$ come nelle figure del paper.
- Aggiunto $\log_{10}(-\Delta_0)$ (la regione con $\Delta_0<0$, il "$\sim -10^{-7}$" della Fig. 1).
- Le diagnostiche usano `data_all` (dati arrotondati), non piu' i file grezzi.


## 1. Import e parametri

In [1]:
import os
import numpy as np
import plotly.graph_objects as go
from plotly.subplots import make_subplots

# ============================================================
# FILE E PARAMETRI
# ============================================================
# Solo h = 1e-6 (valore dell'articolo).
files = {
    r"10^{-6}": "grid_dynamics_7030_h1e-06_sigmaFIX.npz",
}

# Parametri fissi del modello (Sez. II e III del paper)
alpha = 0.1
wEE = 6.95
wII = 6.85

chiE = 0.7
chiI = 0.3

# Numero di cifre decimali a cui arrotondare i dati al caricamento
DECIMALI = 9

# ============================================================
# SALVATAGGIO AUTOMATICO DELLE FIGURE
# ============================================================
# Richiede il pacchetto 'kaleido' (pip install kaleido).
CARTELLA_FIGURE = "figure_esportate_ottobre"
os.makedirs(CARTELLA_FIGURE, exist_ok=True)


def salva_figura(fig, nome_file, scale=2):
    """Salva la figura come PNG (CARTELLA_FIGURE/nome_file.png) e poi la mostra."""
    path = os.path.join(CARTELLA_FIGURE, f"{nome_file}.png")
    try:
        fig.write_image(path, scale=scale)
        print(f"Figura salvata: {path}")
    except Exception as e:
        print(f"ATTENZIONE: impossibile salvare '{path}' ({e}). "
              f"Installa il pacchetto con: pip install kaleido")
    fig.show()


def layout_griglia(n_pannelli, max_colonne=2):
    """Numero di righe e colonne per n_pannelli subplot (1 pannello -> 1x1)."""
    n_cols = min(max_colonne, n_pannelli)
    n_rows = int(np.ceil(n_pannelli / n_cols))
    return n_rows, n_cols

## 2. Caricamento dati

In [2]:
# ============================================================
# CARICAMENTO DATI (arrotondati a DECIMALI cifre) + REGIONE PROIBITA
# ============================================================
# delta_IE e delta_EI sono gli assi della griglia: non vengono arrotondati.
# Gli array 2D hanno indice 0 = delta_EI, indice 1 = delta_IE.
#
# Regione proibita (come nelle Fig. 1-2 del paper): w_EI < 0 oppure
# w_IE < 0. 
# Li' tutti i campi 2D vengono messi a NaN.

CAMPI_ASSI = ["delta_IE", "delta_EI"]

data_all = {}

for h_label, filename in files.items():
    raw = np.load(filename)

    entry = {}
    for key in raw.files:
        if key in CAMPI_ASSI:
            entry[key] = raw[key]
        else:
            entry[key] = np.round(raw[key], DECIMALI)

    DEI, DIE = np.meshgrid(entry["delta_EI"], entry["delta_IE"], indexing="ij")
    proibita = ((wII + DEI) < 0) | ((wEE + DIE) < 0)

    for key, val in entry.items():
        if key not in CAMPI_ASSI and np.ndim(val) == 2:
            val = val.astype(float)
            val[proibita] = np.nan
            entry[key] = val

    entry["proibita"] = proibita
    data_all[h_label] = entry

    righe_proibite = entry["delta_EI"][np.any(proibita, axis=1)]
    print(f"h = {h_label}  <-  {filename}")
    print(f"  griglia: {len(entry['delta_EI'])} x {len(entry['delta_IE'])} (delta_EI x delta_IE)")
    print(f"  punti nella regione proibita (messi a NaN): {int(proibita.sum())}, "
          f"righe delta_EI = {np.round(righe_proibite, 2)}")

h = 10^{-6}  <-  grid_dynamics_7030_h1e-06_sigmaFIX.npz
  griglia: 141 x 140 (delta_EI x delta_IE)
  punti nella regione proibita (messi a NaN): 280, righe delta_EI = [-7.  -6.9]


## 3. $E_0$, $I_0$, $\Sigma_0$, $\Delta_0$ (scala lineare e logaritmica)

### 3.0 Funzione di plot generica (scatter / heatmap / contour)

`plot_quantity` disegna una quantita' di `data_all` nel piano $(\delta_{IE}, \delta_{EI})$ in tre modi, scelti con il parametro `tipo`:

- `"scatter"`: un marker quadrato per punto di griglia, valore esatto, nessuna interpolazione;
- `"heatmap"`: un rettangolo per cella, valore esatto, nessuna interpolazione;
- `"contour"`: curve di livello interpolate tra i punti (aspetto piu' liscio, ma smussa le discontinuita' e approssima i bordi delle zone NaN).

Se `tipo` non viene passato si usa `TIPO_PLOT_DEFAULT` (per ora `"scatter"`): cambiando quella variabile si cambiano tutti i grafici della Sez. 3, di $\log W$ (6.1) e della Sez. 7. Il file PNG viene salvato come `<quantita>_<tipo>.png`, cosi' le versioni non si sovrascrivono.

In [3]:
# ============================================================
# FUNZIONE DI PLOT GENERICA (scatter / heatmap / contour, INTERATTIVO)
# ============================================================
# Un pannello per ciascun h presente in data_all (qui: uno solo).
# Passando il mouse su un punto compare (delta_IE, delta_EI, valore).

TIPO_PLOT_DEFAULT = "scatter"   # "scatter", "heatmap" oppure "contour"


def plot_quantity(quantity_name, colorbar_label=None, cmap="Jet", levels=50,
                  tipo=None, marker_size=4):
    """
    Plot di una quantita' salvata in data_all, scala colore comune.

    tipo        : "scatter", "heatmap" o "contour" (None -> TIPO_PLOT_DEFAULT)
    levels      : numero di livelli, usato solo da "contour"
    marker_size : dimensione dei marker, usata solo da "scatter"
    """
    tipo = TIPO_PLOT_DEFAULT if tipo is None else tipo
    if tipo not in ("scatter", "heatmap", "contour"):
        raise ValueError("tipo deve essere 'scatter', 'heatmap' o 'contour'")

    all_values = [data[quantity_name] for data in data_all.values()]
    vmin = min(np.nanmin(arr) for arr in all_values)
    vmax = max(np.nanmax(arr) for arr in all_values)

    h_labels = list(data_all.keys())
    n_rows, n_cols = layout_griglia(len(h_labels))

    fig = make_subplots(
        rows=n_rows, cols=n_cols,
        subplot_titles=[f"h={h_label}" for h_label in h_labels],
        horizontal_spacing=0.12, vertical_spacing=0.16,
    )

    label = colorbar_label or quantity_name
    hover = ("delta_IE = %{x:.3g}<br>delta_EI = %{y:.3g}<br>"
             + label + " = %{z:.4g}<extra></extra>")

    for idx, h_label in enumerate(h_labels):
        row, col = idx // n_cols + 1, idx % n_cols + 1
        data = data_all[h_label]
        z = data[quantity_name]

        if tipo == "contour":
            trace = go.Contour(
                x=data["delta_IE"], y=data["delta_EI"], z=z,
                zmin=vmin, zmax=vmax, colorscale=cmap, ncontours=levels,
                showscale=(idx == 0), colorbar=dict(title=label),
                contours=dict(coloring="fill", showlines=False),
                hovertemplate=hover,
            )
        elif tipo == "heatmap":
            trace = go.Heatmap(
                x=data["delta_IE"], y=data["delta_EI"], z=z,
                zmin=vmin, zmax=vmax, colorscale=cmap,
                showscale=(idx == 0), colorbar=dict(title=label),
                hovertemplate=hover,
            )
        else:  # scatter: solo i punti con valore finito
            DEI, DIE = np.meshgrid(data["delta_EI"], data["delta_IE"], indexing="ij")
            z_flat = z.ravel()
            ok = np.isfinite(z_flat)
            trace = go.Scattergl(
                x=DIE.ravel()[ok], y=DEI.ravel()[ok], mode="markers",
                marker=dict(color=z_flat[ok], colorscale=cmap, cmin=vmin, cmax=vmax,
                            symbol="square", size=marker_size,
                            showscale=(idx == 0), colorbar=dict(title=label)),
                hovertemplate=hover.replace("%{z", "%{marker.color"),
                showlegend=False,
            )

        fig.add_trace(trace, row=row, col=col)
        fig.update_xaxes(title_text="delta_IE", row=row, col=col)
        fig.update_yaxes(title_text="delta_EI", row=row, col=col)

    fig.update_layout(title=f"{label}  [{tipo}]",
                      height=450 * n_rows + 100, width=500 * n_cols + 150)
    salva_figura(fig, f"{quantity_name}_{tipo}")


Per le versioni in scala logaritmica calcoliamo `log10_<quantita>` mascherando (NaN) i punti con valore $\le 0$. Poiche' $\Delta_0$ e' negativo in buona parte del piano (primo quadrante: $\Delta_0 \approx -\chi_I I_0$), calcoliamo anche $\log_{10}(-\Delta_0)$, dove $\Delta_0 < 0$.

In [4]:
# ============================================================
# CAMPI IN SCALA LOGARITMICA (log10)
# ============================================================

def log10_positivo(val):
    """log10 dove val > 0 (e finito), NaN altrove."""
    with np.errstate(divide="ignore", invalid="ignore"):
        return np.where(np.isfinite(val) & (val > 0), np.log10(np.where(val > 0, val, np.nan)), np.nan)


for h_label, data in data_all.items():
    for base_name in ["E0", "I0", "Sigma0", "Delta0"]:
        data[f"log10_{base_name}"] = log10_positivo(data[base_name])
    data["log10_minus_Delta0"] = log10_positivo(-data["Delta0"])

print("Campi log10 calcolati: log10_E0, log10_I0, log10_Sigma0, log10_Delta0, log10_minus_Delta0")

Campi log10 calcolati: log10_E0, log10_I0, log10_Sigma0, log10_Delta0, log10_minus_Delta0


### 3.1 $E_0$

In [5]:
plot_quantity("E0", colorbar_label="E0")

Figura salvata: figure_esportate_ottobre\E0_scatter.png


In [6]:
plot_quantity("log10_E0", colorbar_label="log10(E0)")

Figura salvata: figure_esportate_ottobre\log10_E0_scatter.png


### 3.2 $I_0$

In [7]:
plot_quantity("I0", colorbar_label="I0")

Figura salvata: figure_esportate_ottobre\I0_scatter.png


In [8]:
plot_quantity("log10_I0", colorbar_label="log10(I0)")

Figura salvata: figure_esportate_ottobre\log10_I0_scatter.png


### 3.3 $\Sigma_0$

In [9]:
plot_quantity("Sigma0", colorbar_label="Sigma0")

Figura salvata: figure_esportate_ottobre\Sigma0_scatter.png


In [10]:
plot_quantity("log10_Sigma0", colorbar_label="log10(Sigma0)")

Figura salvata: figure_esportate_ottobre\log10_Sigma0_scatter.png


### 3.4 $\Delta_0$

In [11]:
plot_quantity("Delta0", colorbar_label="Delta0")

Figura salvata: figure_esportate_ottobre\Delta0_scatter.png


In [12]:
plot_quantity("log10_Delta0", colorbar_label="log10(Delta0)  [solo Delta0 > 0]")

Figura salvata: figure_esportate_ottobre\log10_Delta0_scatter.png


In [13]:
plot_quantity("log10_minus_Delta0", colorbar_label="log10(-Delta0)  [solo Delta0 < 0]")

Figura salvata: figure_esportate_ottobre\log10_minus_Delta0_scatter.png


## 4. Funzioni di correlazione e risposta

Le 4 funzioni di correlazione ($C_{\Sigma\Sigma}, C_{\Sigma\Delta}, C_{\Delta\Sigma}, C_{\Delta\Delta}$) e le 4 funzioni di risposta ($R_{\Sigma\Sigma}, R_{\Sigma\Delta}, R_{\Delta\Sigma}, R_{\Delta\Delta}$), nel caso di autovalori reali (Eq. 10-13, A38) e complessi (Eq. 14, A39) di Nandi *et al.* Le formule coincidono con $C(t) = e^{At}\sigma$ e $R(t)=e^{At}$ (verificato), con $\lambda_1$ = autovalore maggiore.

In [14]:
# ============================================================
# FUNZIONI DI CORRELAZIONE E RISPOSTA (caso reale e complesso)
# ============================================================

def compute_corr_resp(i, j, data, t):
    """
    Correlazioni e risposte nel punto di griglia (i, j) [i su delta_EI,
    j su delta_IE], sull'array temporale t.
    Chiavi: 'C_SS','C_SD','C_DS','C_DD','R_SS','R_SD','R_DS','R_DD','is_complex'
    (S = Sigma, D = Delta).
    """
    x = data["A_x"][i, j]; y = data["A_y"][i, j]; z = data["A_z"][i, j]; w = data["A_w"][i, j]
    s11 = data["sigma11"][i, j]; s12 = data["sigma12"][i, j]; s22 = data["sigma22"][i, j]
    is_cplx = data["is_complex"][i, j]

    if is_cplx == 1:
        a = data["lambda_re"][i, j]; b = data["lambda_im"][i, j]
        eat = np.exp(a * t); cosbt = np.cos(b * t); sinbt = np.sin(b * t)

        C_SS = s11 * eat * cosbt + ((x - a) * s11 + y * s12) / b * eat * sinbt
        C_SD = s12 * eat * cosbt + ((x - a) * s12 + y * s22) / b * eat * sinbt
        C_DS = s12 * eat * cosbt + (z * s11 - (x - a) * s12) / b * eat * sinbt
        C_DD = s22 * eat * cosbt + (z * s12 - (x - a) * s22) / b * eat * sinbt

        R_SS = eat * cosbt + (x - a) / b * eat * sinbt
        R_SD = y / b * eat * sinbt
        R_DS = z / b * eat * sinbt
        R_DD = eat * cosbt - (x - a) / b * eat * sinbt

    else:
        L1 = data["lambda1"][i, j]; L2 = data["lambda2"][i, j]
        rad = np.sqrt((x - w)**2 + 4 * y * z)
        e1 = np.exp(L1 * t); e2 = np.exp(L2 * t)

        C_SS = (((x - L2) * s11 + y * s12) * e1 - ((x - L1) * s11 + y * s12) * e2) / rad
        C_SD = (((x - L2) * s12 + y * s22) * e1 - ((x - L1) * s12 + y * s22) * e2) / rad
        C_DS = ((z * s11 - (x - L1) * s12) * e1 - (z * s11 - (x - L2) * s12) * e2) / rad
        C_DD = ((z * s12 - (x - L1) * s22) * e1 - (z * s12 - (x - L2) * s22) * e2) / rad

        R_SS = ((x - L2) * e1 - (x - L1) * e2) / rad
        R_SD = y * (e1 - e2) / rad
        R_DS = z * (e1 - e2) / rad
        R_DD = ((x - L2) * e2 - (x - L1) * e1) / rad

    return {
        "C_SS": C_SS, "C_SD": C_SD, "C_DS": C_DS, "C_DD": C_DD,
        "R_SS": R_SS, "R_SD": R_SD, "R_DS": R_DS, "R_DD": R_DD,
        "is_complex": is_cplx,
    }

### 4.1 Plot: scegli manualmente delta_IE, delta_EI

Imposta `delta_IE_target` e `delta_EI_target` (si usa il punto di griglia piu' vicino), poi esegui la cella successiva: a sinistra le 4 correlazioni, a destra le 4 risposte. Con `NORMALIZZA = True` ogni correlazione e' divisa per il proprio valore in $t=0$, come nelle Fig. 3, 4 e 6 del paper. Nel primo quadrante $\sigma = 0$ alla precisione usata, quindi le correlazioni li' sono nulle.

In [15]:
# ============================================================
# PARAMETRI: scegli qui il punto (delta_IE, delta_EI)
# ============================================================

delta_IE_target = 3.5
delta_EI_target = -0.6

t_corr = np.linspace(0, 100, 20000)   # asse temporale (ms)

NORMALIZZA = True   # True -> C(t)/C(0) come nel paper; False -> C(t)

In [16]:
# ============================================================
# PLOT: CORRELAZIONI (sinistra) E RISPOSTE (destra)
# ============================================================

corr_colors = {"C_SS": "black", "C_SD": "red", "C_DS": "green", "C_DD": "blue"}
resp_colors = {"R_SS": "black", "R_SD": "red", "R_DS": "green", "R_DD": "blue"}

h_labels = list(data_all.keys())
etichetta_C = "C(t)/C(0)" if NORMALIZZA else "C(t)"

fig = make_subplots(
    rows=len(h_labels), cols=2,
    subplot_titles=sum(
        [[f"Correlazioni {etichetta_C}, h={h}", f"Risposte R(t), h={h}"] for h in h_labels], []
    ),
    horizontal_spacing=0.08, vertical_spacing=0.08,
)

for row, h_label in enumerate(h_labels, start=1):
    data = data_all[h_label]

    i = int(np.argmin(np.abs(data["delta_EI"] - delta_EI_target)))
    j = int(np.argmin(np.abs(data["delta_IE"] - delta_IE_target)))
    actual_dei = data["delta_EI"][i]
    actual_die = data["delta_IE"][j]

    res = compute_corr_resp(i, j, data, t_corr)
    regime = "complesso" if res["is_complex"] == 1 else "reale"

    for key, color in corr_colors.items():
        y_val = res[key]
        if NORMALIZZA:
            if y_val[0] != 0 and np.isfinite(y_val[0]):
                y_val = y_val / y_val[0]
            else:
                print(f"  {key}(0) = {y_val[0]}: non normalizzabile, mostrata non normalizzata")

        fig.add_trace(
            go.Scatter(
                x=t_corr, y=y_val, mode="lines", line=dict(color=color),
                name=key, legendgroup=key, showlegend=(row == 1),
                hovertemplate=f"{key}<br>t=%{{x:.3g}}<br>valore=%{{y:.4g}}<extra></extra>",
            ),
            row=row, col=1,
        )

    for key, color in resp_colors.items():
        fig.add_trace(
            go.Scatter(
                x=t_corr, y=res[key], mode="lines", line=dict(color=color, dash="dot"),
                name=key, legendgroup=key, showlegend=(row == 1),
                hovertemplate=f"{key}<br>t=%{{x:.3g}}<br>valore=%{{y:.4g}}<extra></extra>",
            ),
            row=row, col=2,
        )

    fig.update_xaxes(title_text="t (ms)", row=row, col=1)
    fig.update_xaxes(title_text="t (ms)", row=row, col=2)
    fig.update_yaxes(title_text=f"{etichetta_C} ({regime})", row=row, col=1)
    fig.update_yaxes(title_text="R(t)", row=row, col=2)

    print(f"h={h_label} | punto piu' vicino: delta_IE={actual_die:.3f}, "
          f"delta_EI={actual_dei:.3f} | regime {regime}")

fig.update_layout(
    height=420 * len(h_labels) + 80, width=1150,
    title=f"Correlazioni e risposte a delta_IE~{delta_IE_target}, delta_EI~{delta_EI_target}",
)
salva_figura(fig, "correlazioni_risposte")

h=10^{-6} | punto piu' vicino: delta_IE=3.500, delta_EI=-0.600 | regime complesso
Figura salvata: figure_esportate_ottobre\correlazioni_risposte.png


## 5. Diagramma degli autovalori (ricostruzione Fig. 2, Nandi et al.)

I 4 pannelli della Fig. 2 del paper: regione reale/complessa, parte immaginaria (solo dove complessa), parte reale di $\lambda_1$ e di $\lambda_2$. Nel ramo complesso `lambda1` e `lambda2` sono salvati entrambi uguali a `lambda_re` dallo script di simulazione, quindi sono continui su tutta la griglia.

In [17]:
# ============================================================
# RICOSTRUZIONE FIG. 2 (Nandi et al.)
# ============================================================

def plot_eigen_phase_diagram(h_label):
    data = data_all[h_label]

    delta_IE = data["delta_IE"]
    delta_EI = data["delta_EI"]

    is_cplx   = data["is_complex"]
    lambda_im = data["lambda_im"]
    lambda1   = data["lambda1"]
    lambda2   = data["lambda2"]

    lambda_im_masked = np.where(is_cplx == 1, lambda_im, np.nan)

    fig = make_subplots(
        rows=2, cols=2,
        subplot_titles=[
            "Regione autovalori reali/complessi",
            "Parte immaginaria (solo dove complessi)",
            "Parte reale di lambda1",
            "Parte reale di lambda2",
        ],
        horizontal_spacing=0.12, vertical_spacing=0.15,
    )

    fig.add_trace(
        go.Heatmap(
            x=delta_IE, y=delta_EI, z=is_cplx,
            colorscale=[[0, "cyan"], [0.5, "cyan"], [0.5, "red"], [1, "red"]],
            zmin=0, zmax=1, showscale=False,
            hovertemplate=(
                "delta_IE=%{x:.3g}<br>delta_EI=%{y:.3g}<br>"
                "regime=%{z} (0=reale, 1=complesso)<extra></extra>"
            ),
        ),
        row=1, col=1,
    )
    fig.add_trace(
        go.Heatmap(
            x=delta_IE, y=delta_EI, z=lambda_im_masked, colorscale="Jet",
            colorbar=dict(x=1.0, y=0.80, len=0.42, thickness=13, title="b"),
            hovertemplate="delta_IE=%{x:.3g}<br>delta_EI=%{y:.3g}<br>b (Im lambda)=%{z:.4g}<extra></extra>",
        ),
        row=1, col=2,
    )
    fig.add_trace(
        go.Heatmap(
            x=delta_IE, y=delta_EI, z=lambda1, colorscale="Jet",
            colorbar=dict(x=0.44, y=0.19, len=0.42, thickness=13, title="lambda1"),
            hovertemplate="delta_IE=%{x:.3g}<br>delta_EI=%{y:.3g}<br>Re(lambda1)=%{z:.4g}<extra></extra>",
        ),
        row=2, col=1,
    )
    fig.add_trace(
        go.Heatmap(
            x=delta_IE, y=delta_EI, z=lambda2, colorscale="Jet",
            colorbar=dict(x=1.0, y=0.19, len=0.42, thickness=13, title="lambda2"),
            hovertemplate="delta_IE=%{x:.3g}<br>delta_EI=%{y:.3g}<br>Re(lambda2)=%{z:.4g}<extra></extra>",
        ),
        row=2, col=2,
    )

    for row in [1, 2]:
        for col in [1, 2]:
            fig.update_xaxes(title_text="delta_IE", row=row, col=col)
            fig.update_yaxes(title_text="delta_EI", row=row, col=col)

    fig.update_layout(
        title=f"Diagramma degli autovalori (Fig. 2 di Nandi et al.) - h = {h_label}",
        height=800, width=950,
    )
    salva_figura(fig, "diagramma_autovalori")


for h_label in data_all.keys():
    plot_eigen_phase_diagram(h_label)

Figura salvata: figure_esportate_ottobre\diagramma_autovalori.png


## 6. Tasso di produzione di entropia $W$



$$W = -\frac{\delta^2}{(A_{EE}+A_{II})\,E_0\,I_0}, \qquad \delta = \sqrt{\chi_E/\chi_I}\,A_{EI}\,I_0 - \sqrt{\chi_I/\chi_E}\,A_{IE}\,E_0 .$$

Alla precisione usata ($E_0 < 10^{-9} \to 0$) i punti con $W$ non finito sono di due tipi:

- **$W = 0/0$ (NaN)**: $E_0 = 0$ **e** $A_{EI} = 0$. Primo quadrante: l'input $S_E \le 0$, quindi $f(S_E) = 0$ e $f'(S_E) = 0$; il sistema collassa a 1D (solo neuroni inibitori), e' all'equilibrio e il valore fisico e' $W = 0$. Qui le analisi successive non vengono fatte (maschera `W_00`).
- **$W = \delta^2/0 = \infty$**: $E_0 = 0$ ma $A_{EI} \neq 0$. E' **un solo punto** ($\delta_{EI} = 0.1$, $\delta_{IE} = 0$, accanto al punto critico, sul bordo del primo quadrante) ed e' probabilmente un **artefatto numerico**: li' $S_E \approx 6\cdot 10^{-16}$, cioe' zero entro la precisione di macchina, e il segno di $S_E$ decide da solo se $A_{EI} = -w_{EI}$ (punto "2D") o $A_{EI} = 0$ (punto 1D); inoltre $E_0 \approx 3.6\cdot 10^{-12}$ e' rumore del solutore, arrotondato a zero. Va considerato un punto di confine del primo quadrante. Dettagli nella Sez. 8. Per ora il punto **non** e' mascherato.

In [18]:
# ============================================================
# TASSO DI PRODUZIONE DI ENTROPIA + CLASSIFICAZIONE DEI PUNTI
# ============================================================

def compute_entropy_rate(data):
    """Ritorna W, numeratore (delta^2), denominatore (Tr(A)*E0*I0) e la maschera 0/0."""
    E0 = data["E0"]; I0 = data["I0"]
    A_EE = data["A_EE"]; A_EI = data["A_EI"]; A_IE = data["A_IE"]; A_II = data["A_II"]

    delta_term = (
        np.sqrt(chiE / chiI) * A_EI * I0
        - np.sqrt(chiI / chiE) * A_IE * E0
    )
    numeratore = delta_term**2
    denominatore = (A_EE + A_II) * E0 * I0

    with np.errstate(divide="ignore", invalid="ignore"):
        W = -numeratore / denominatore

    mask_00 = (numeratore == 0) & (denominatore == 0)
    return W, numeratore, denominatore, mask_00


W_matrices = {}
W_00_masks = {}
W_num = {}
W_den = {}

for h_label, data in data_all.items():
    W, num, den, mask_00 = compute_entropy_rate(data)
    W_matrices[h_label] = W
    W_00_masks[h_label] = mask_00
    W_num[h_label] = num
    W_den[h_label] = den
    data["log10_W"] = log10_positivo(W)

    valido = ~data["proibita"]
    print(f"h = {h_label}")
    print(f"  W = 0/0 (primo quadrante, 1D, mascherati)   : {int(np.sum(mask_00 & valido))}")
    print(f"  W = inf (delta^2/0, 2D, NON mascherati)     : {int(np.sum(np.isinf(W) & valido))}")
    print(f"  W finito e > 0                               : {int(np.sum(np.isfinite(W) & (W > 0) & valido))}")
    print(f"  W finito e = 0                               : {int(np.sum((W == 0) & valido))}")
    print(f"  regione proibita (NaN)                       : {int(np.sum(data['proibita']))}")

h = 10^{-6}
  W = 0/0 (primo quadrante, 1D, mascherati)   : 6544
  W = inf (delta^2/0, 2D, NON mascherati)     : 1
  W finito e > 0                               : 12915
  W finito e = 0                               : 0
  regione proibita (NaN)                       : 280


### 6.1 $W$: contour plot in scala logaritmica

In [19]:
plot_quantity("log10_W", colorbar_label="log10(W)")

Figura salvata: figure_esportate_ottobre\log10_W_scatter.png


### 6.2 $W$: scatter plot in scala logaritmica

Ogni punto della griglia e' un marker. Colorati con $\log_{10} W$ i punti con $W$ finito e positivo; in grigio i punti con $W = \infty$, in nero i punti $W = 0/0$ (primo quadrante, 1D). La regione proibita non e' disegnata.

In [20]:
# ============================================================
# SCATTER PLOT DI W IN SCALA LOGARITMICA
# ============================================================

for h_label, data in data_all.items():
    W = W_matrices[h_label]
    mask_00 = W_00_masks[h_label]
    valido = ~data["proibita"]

    DEI, DIE = np.meshgrid(data["delta_EI"], data["delta_IE"], indexing="ij")
    die_flat, dei_flat = DIE.ravel(), DEI.ravel()
    W_flat = W.ravel()
    logW_flat = data["log10_W"].ravel()

    m_pos  = (np.isfinite(W) & (W > 0) & valido).ravel()
    m_inf  = (np.isinf(W) & valido).ravel()
    m_00   = (mask_00 & valido).ravel()
    m_zero = ((W == 0) & valido).ravel()

    fig = go.Figure()

    fig.add_trace(go.Scattergl(
        x=die_flat[m_00], y=dei_flat[m_00], mode="markers",
        marker=dict(color="black", size=6),
        name=f"W = 0/0 (1D, equilibrio) — {int(m_00.sum())} punti",
        hovertemplate="delta_IE=%{x:.3g}<br>delta_EI=%{y:.3g}<extra>W = 0/0</extra>",
    ))
    fig.add_trace(go.Scattergl(
        x=die_flat[m_inf], y=dei_flat[m_inf], mode="markers",
        marker=dict(color="gray", size=6),
        name=f"W = ∞ (δ²/0) — {int(m_inf.sum())} punti",
        hovertemplate="delta_IE=%{x:.3g}<br>delta_EI=%{y:.3g}<extra>W = ∞</extra>",
    ))
    if m_zero.any():
        fig.add_trace(go.Scattergl(
            x=die_flat[m_zero], y=dei_flat[m_zero], mode="markers",
            marker=dict(color="white", size=6, line=dict(color="black", width=1)),
            name=f"W = 0 (finito) — {int(m_zero.sum())} punti",
            hovertemplate="delta_IE=%{x:.3g}<br>delta_EI=%{y:.3g}<extra>W = 0</extra>",
        ))
    fig.add_trace(go.Scattergl(
        x=die_flat[m_pos], y=dei_flat[m_pos], mode="markers",
        marker=dict(color=logW_flat[m_pos], colorscale="Jet", size=6,
                    showscale=True, colorbar=dict(title="log10(W)")),
        name=f"W finito > 0 — {int(m_pos.sum())} punti",
        customdata=W_flat[m_pos],
        hovertemplate=("delta_IE=%{x:.3g}<br>delta_EI=%{y:.3g}<br>"
                       "log10(W)=%{marker.color:.4g}<br>W=%{customdata:.4g}<extra></extra>"),
    ))

    fig.update_xaxes(title_text="delta_IE")
    fig.update_yaxes(title_text="delta_EI")
    fig.update_layout(
        title=f"Tasso di produzione di entropia, log10(W) — h = {h_label}",
        height=650, width=800,
        legend=dict(orientation="h", yanchor="top", y=-0.12, xanchor="center", x=0.5),
    )
    salva_figura(fig, "W_scatter_log")

Figura salvata: figure_esportate_ottobre\W_scatter_log.png


### 6.3 $W$ lungo linee a $\delta_{EI}$ fissato e a $\delta_{IE}$ fissato

$W$ e' gia' un campo 2D (`W_matrices`): "lungo una linea" e' una riga o una colonna di quella matrice. La prima figura fissa $\delta_{EI}$ e fa variare $\delta_{IE}$; la seconda il contrario.

In [21]:
# ============================================================
# W LUNGO LINEE A delta_EI FISSATO E A delta_IE FISSATO
# ============================================================

valori_dei = [-5, -2.5, -0.5, 0, 2.5, 5]   # linee orizzontali: delta_EI fissato
valori_die = [-5, -2.5, -0.5, 0, 2.5, 5]   # linee verticali: delta_IE fissato

W_LINE_COLORS = [
    "rgb(31,119,180)", "rgb(174,199,232)", "rgb(214,39,40)",
    "rgb(44,160,44)", "rgb(255,127,14)", "rgb(148,103,189)",
]
W_LINE_SYMBOLS = ["circle", "square", "triangle-up", "diamond", "pentagon", "star"]


def plot_W_lines_interactive(axis, target_values, xlabel, legend_prefix, title, nome_file, yscale="log"):
    """
    axis="dei" -> delta_EI fissato, delta_IE variabile.
    axis="die" -> delta_IE fissato, delta_EI variabile.
    In scala log i punti con W <= 0 o non finito non vengono disegnati.
    """
    h_labels = list(data_all.keys())
    n_rows, n_cols = layout_griglia(len(h_labels))

    fig = make_subplots(
        rows=n_rows, cols=n_cols,
        subplot_titles=[f"h={h}" for h in h_labels],
        horizontal_spacing=0.08, vertical_spacing=0.12,
    )

    for idx, h_label in enumerate(h_labels):
        row, col = idx // n_cols + 1, idx % n_cols + 1
        data = data_all[h_label]
        W = W_matrices[h_label]

        for j, target in enumerate(target_values):
            if axis == "dei":
                i = int(np.argmin(np.abs(data["delta_EI"] - target)))
                var_vals = data["delta_IE"]
                W_line = W[i, :]
            elif axis == "die":
                k = int(np.argmin(np.abs(data["delta_IE"] - target)))
                var_vals = data["delta_EI"]
                W_line = W[:, k]
            else:
                raise ValueError("axis deve essere 'dei' o 'die'")

            order = np.argsort(var_vals)
            var_sorted = var_vals[order]
            W_sorted = W_line[order]
            if yscale == "log":
                W_sorted = np.where(np.isfinite(W_sorted) & (W_sorted > 0), W_sorted, np.nan)

            color = W_LINE_COLORS[j % len(W_LINE_COLORS)]
            symbol = W_LINE_SYMBOLS[j % len(W_LINE_SYMBOLS)]

            fig.add_trace(
                go.Scatter(
                    x=var_sorted, y=W_sorted, mode="lines+markers",
                    name=f"{legend_prefix} = {target:g}",
                    legendgroup=f"target_{target}", showlegend=(idx == 0),
                    line=dict(color=color, dash="dash", width=1.5),
                    marker=dict(symbol=symbol, size=6, color=color),
                    hovertemplate=(
                        f"{legend_prefix} = {target:g}<br>" + xlabel +
                        " = %{x:.4g}<br>W = %{y:.4g}<extra></extra>"
                    ),
                ),
                row=row, col=col,
            )

        fig.update_xaxes(title_text=xlabel, row=row, col=col)
        fig.update_yaxes(title_text="W", type="log" if yscale == "log" else "linear", row=row, col=col)

    fig.update_layout(title=title, height=450 * n_rows + 50, width=550 * n_cols + 250,
                      legend=dict(title=legend_prefix))
    salva_figura(fig, nome_file)


plot_W_lines_interactive(
    "dei", valori_dei, "delta_IE", "delta_EI",
    "Tasso di entropia W lungo linee a delta_EI fissato",
    nome_file="entropia_linee_delta_EI_fissato",
)
plot_W_lines_interactive(
    "die", valori_die, "delta_EI", "delta_IE",
    "Tasso di entropia W lungo linee a delta_IE fissato",
    nome_file="entropia_linee_delta_IE_fissato",
)

Figura salvata: figure_esportate_ottobre\entropia_linee_delta_EI_fissato.png


Figura salvata: figure_esportate_ottobre\entropia_linee_delta_IE_fissato.png


### 6.4 Numeratore e denominatore di $W$

In [22]:
# ============================================================
# NUMERATORE (delta^2) E DENOMINATORE (Tr(A)*E0*I0) DI W
# ============================================================

for h_label, data in data_all.items():
    numeratore = W_num[h_label]
    denominatore = W_den[h_label]

    log_num = log10_positivo(numeratore)
    log_den = log10_positivo(np.abs(denominatore))

    fig = make_subplots(
        rows=1, cols=2,
        subplot_titles=["log10(numeratore) = log10(delta^2)",
                        "log10(|denominatore|) = log10(|Tr(A)*E0*I0|)"],
    )
    fig.add_trace(
        go.Heatmap(x=data["delta_IE"], y=data["delta_EI"], z=log_num, colorscale="Jet",
                   colorbar=dict(title="log10(delta^2)", x=0.44)),
        row=1, col=1,
    )
    fig.add_trace(
        go.Heatmap(x=data["delta_IE"], y=data["delta_EI"], z=log_den, colorscale="Jet",
                   colorbar=dict(title="log10(|denom|)", x=1.02)),
        row=1, col=2,
    )
    for col in [1, 2]:
        fig.update_xaxes(title_text="delta_IE", row=1, col=col)
        fig.update_yaxes(title_text="delta_EI", row=1, col=col)

    fig.update_layout(title=f"Numeratore e denominatore di W — h={h_label} (bianco = zero)",
                      height=500, width=1100)
    salva_figura(fig, "numeratore_denominatore_W")

Figura salvata: figure_esportate_ottobre\numeratore_denominatore_W.png


### 6.5 Diagnostica: collasso a 1D nel primo quadrante

Il collasso a 1D (vedi note Dario) richiede $E_0 = 0$ **e** $A_{EI} = 0$ insieme (niente rumore proprio su $\xi_E$ e niente accoppiamento $\xi_I \to \xi_E$). Alla precisione usata "zero" significa esattamente zero dopo l'arrotondamento. La cella verifica anche che il collasso 1D coincida con i punti $W = 0/0$.

In [23]:
# ============================================================
# DIAGNOSTICA: collasso 1D vs 2D genuino vs misto
# ============================================================
# Categorie: 0 = collasso 1D (E0 = 0 e A_EI = 0)
#            1 = 2D genuino (E0 != 0 e A_EI != 0)
#            2 = misto (solo uno dei due nullo: qui e' l'unico punto con W = inf,
#                artefatto numerico sul bordo del primo quadrante, vedi Sez. 8)

for h_label, data in data_all.items():
    E0, A_EI = data["E0"], data["A_EI"]
    valido = ~data["proibita"]

    collasso_1D = (E0 == 0) & (A_EI == 0) & valido
    genuino_2D = (E0 != 0) & (A_EI != 0) & valido
    misto = valido & ~collasso_1D & ~genuino_2D

    category = np.full(E0.shape, np.nan)
    category[collasso_1D] = 0
    category[genuino_2D] = 1
    category[misto] = 2

    print(f"h = {h_label}")
    print(f"  collasso 1D : {int(collasso_1D.sum())}")
    print(f"  2D genuino  : {int(genuino_2D.sum())}")
    print(f"  misto       : {int(misto.sum())}")
    coincide = np.array_equal(collasso_1D, W_00_masks[h_label] & valido)
    print(f"  collasso 1D coincide con i punti W = 0/0: {coincide}")

    discrete_colorscale = [
        [0.00, "royalblue"], [0.333, "royalblue"],
        [0.334, "crimson"], [0.666, "crimson"],
        [0.667, "lightgray"], [1.00, "lightgray"],
    ]

    with np.errstate(divide="ignore", invalid="ignore"):
        log_AEI = np.where(np.abs(A_EI) > 0, np.log10(np.abs(A_EI)), np.nan)

    fig = make_subplots(
        rows=1, cols=2,
        subplot_titles=["Collasso 1D (blu) / 2D genuino (rosso) / misto (grigio)",
                        "log10|A_EI| (bianco = esattamente zero)"],
        horizontal_spacing=0.14,
    )
    fig.add_trace(
        go.Heatmap(
            x=data["delta_IE"], y=data["delta_EI"], z=category,
            zmin=0, zmax=2, colorscale=discrete_colorscale,
            colorbar=dict(title="regime", x=0.43, tickvals=[0.33, 1.0, 1.67],
                          ticktext=["collasso 1D", "2D genuino", "misto"]),
            hovertemplate=("delta_IE=%{x:.3g}<br>delta_EI=%{y:.3g}<br>"
                           "categoria=%{z} (0=1D, 1=2D, 2=misto)<extra></extra>"),
        ),
        row=1, col=1,
    )
    fig.add_trace(
        go.Heatmap(
            x=data["delta_IE"], y=data["delta_EI"], z=log_AEI, colorscale="Jet",
            colorbar=dict(title="log10|A_EI|", x=1.02),
            hovertemplate="delta_IE=%{x:.3g}<br>delta_EI=%{y:.3g}<br>log10|A_EI|=%{z:.3g}<extra></extra>",
        ),
        row=1, col=2,
    )
    for col in [1, 2]:
        fig.update_xaxes(title_text="delta_IE", row=1, col=col)
        fig.update_yaxes(title_text="delta_EI", row=1, col=col)

    fig.update_layout(title=f"Diagnostica collasso 1D — h={h_label}", height=520, width=1150)
    salva_figura(fig, "diagnostica_collasso_1D")

h = 10^{-6}
  collasso 1D : 6544
  2D genuino  : 12915
  misto       : 1
  collasso 1D coincide con i punti W = 0/0: True
Figura salvata: figure_esportate_ottobre\diagnostica_collasso_1D.png


## 7. Fluttuazione relativa dell'attivita' totale

$\sqrt{\sigma_{11}}/\Sigma_0$. Nota: le fluttuazioni $\xi$ sono gia' scalate per $\sqrt{N}$, quindi la fluttuazione relativa fisica e' $\sqrt{\sigma_{11}/N}/\Sigma_0$. Nel primo quadrante $\sigma_{11} = 0$ alla precisione usata, quindi li' la quantita' non e' definita. Valori molto grandi vicino al punto critico e alla linea di transizione riflettono la divergenza critica ($\det A \to 0$): li' la teoria lineare non e' affidabile.

In [24]:
# ============================================================
# FLUTTUAZIONE RELATIVA: sqrt(sigma11) / Sigma0
# ============================================================

for h_label, data in data_all.items():
    sigma11 = data["sigma11"]
    Sigma0 = data["Sigma0"]

    mask_valid = (
        np.isfinite(sigma11) & (sigma11 >= 0)
        & np.isfinite(Sigma0) & (Sigma0 > 0)
    )

    fluct_rel_Sigma = np.full_like(sigma11, np.nan, dtype=float)
    fluct_rel_Sigma[mask_valid] = np.sqrt(sigma11[mask_valid]) / Sigma0[mask_valid]

    data["fluct_rel_Sigma"] = fluct_rel_Sigma
    data["log10_fluct_rel_Sigma"] = log10_positivo(fluct_rel_Sigma)
    data["log10_sigma11"] = log10_positivo(sigma11)

print("Calcolati: fluct_rel_Sigma, log10_fluct_rel_Sigma, log10_sigma11")

Calcolati: fluct_rel_Sigma, log10_fluct_rel_Sigma, log10_sigma11


In [25]:
plot_quantity("log10_sigma11", colorbar_label="log10(sigma11)")

Figura salvata: figure_esportate_ottobre\log10_sigma11_scatter.png


In [26]:
plot_quantity("log10_fluct_rel_Sigma", colorbar_label="log10[sqrt(sigma11) / Sigma0]")

Figura salvata: figure_esportate_ottobre\log10_fluct_rel_Sigma_scatter.png


In [27]:
# ============================================================
# FLUTTUAZIONE RELATIVA: scatter con scala colore sul vero min/max
# ============================================================

for h_label, d in data_all.items():
    DEI, DIE = np.meshgrid(d["delta_EI"], d["delta_IE"], indexing="ij")
    val_flat = d["log10_fluct_rel_Sigma"].ravel()
    mask = np.isfinite(val_flat)
    vmin, vmax = float(np.min(val_flat[mask])), float(np.max(val_flat[mask]))

    fig = go.Figure(go.Scattergl(
        x=DIE.ravel()[mask], y=DEI.ravel()[mask], mode="markers",
        marker=dict(color=val_flat[mask], colorscale="Jet", cmin=vmin, cmax=vmax,
                    size=5, showscale=True, colorbar=dict(title="log10[sqrt(sigma11)/Sigma0]")),
        hovertemplate=("delta_IE=%{x:.3g}<br>delta_EI=%{y:.3g}<br>"
                       "log10(fluct_rel)=%{marker.color:.3g}<extra></extra>"),
    ))
    fig.update_xaxes(title_text="delta_IE")
    fig.update_yaxes(title_text="delta_EI")
    fig.update_layout(
        title=f"Fluttuazione relativa log10[sqrt(sigma11)/Sigma0] — h={h_label} "
              f"(scala {vmin:.2f} ÷ {vmax:.2f})",
        height=650, width=800,
    )
    salva_figura(fig, "fluttuazione_relativa_scatter")

Figura salvata: figure_esportate_ottobre\fluttuazione_relativa_scatter.png


## 8. Diagnostica del punto con $W = \infty$ (superfluo (?) )

Il punto con $W = \delta^2/0 = \infty$ e' uno solo (ed e' anche l'unico punto "misto" della Sez. 6.5). Questa cella lo trova e stampa:

- posizione sulla griglia, $w_{EI} = w_{II}+\delta_{EI}$, $w_{IE} = w_{EE}+\delta_{IE}$;
- $E_0, I_0, \Sigma_0, \Delta_0$ **sia arrotondati** (`data_all`) **sia grezzi** dal file `.npz`, per vedere se $E_0 = 0$ e' vero o solo un effetto di `DECIMALI`;
- l'input $S_E = w_{EE}E_0 - w_{EI}I_0 + h$: con $f(S) = \tanh S$ per $S>0$ e $0$ altrimenti, $A_{EI} \neq 0$ richiede $S_E > 0$, e quindi $E_0 > 0$ strettamente (dall'equazione di punto fisso $\alpha E_0 = (1-E_0) f(S_E)$);
- la matrice di drift in base $(E,I)$ e in base $(\Sigma,\Delta)$, traccia e determinante;
- la covarianza $\sigma$ in base $(\Sigma,\Delta)$;
- $\delta$, numeratore e denominatore di $W$, $W$ ricalcolato con i dati grezzi;
- gli autovalori salvati e quelli ricalcolati con `np.linalg.eigvals` (le due matrici di drift sono simili, quindi devono coincidere);
- un intorno $3\times 3$ di $E_0$ e $W$ per vedere dove si trova il punto rispetto al primo quadrante.

In [28]:
# ============================================================
# DIAGNOSTICA DEL PUNTO CON W = inf
# ============================================================
# Solo stampa: nessun campo di data_all viene modificato.
# I valori "grezzi" vengono riletti dal file .npz (non arrotondati).

h_label = list(data_all.keys())[0]
data = data_all[h_label]
raw = np.load(files[h_label])
h_val = 1e-6

W = W_matrices[h_label]
idx_inf = np.argwhere(np.isinf(W) & ~data["proibita"])
print(f"h = {h_label}: punti con W = inf trovati: {len(idx_inf)}\n")


def riga(nome, arrotondato, grezzo=None):
    """Stampa una quantita' arrotondata e (se c'e') grezza."""
    if grezzo is None:
        print(f"  {nome:<22} = {arrotondato: .12e}")
    else:
        print(f"  {nome:<22} = {arrotondato: .12e}   (grezzo: {grezzo: .12e})")


for i, j in idx_inf:
    dei = data["delta_EI"][i]
    die = data["delta_IE"][j]
    wEI = wII + dei
    wIE = wEE + die

    print("=" * 72)
    print(f"Punto di griglia (i, j) = ({i}, {j})")
    print(f"  delta_EI = {dei:.4f}  ->  w_EI = w_II + delta_EI = {wEI:.4f}")
    print(f"  delta_IE = {die:.4f}  ->  w_IE = w_EE + delta_IE = {wIE:.4f}")

    # ---------- stato stazionario ----------
    print("\n--- Stato stazionario ---")
    for k in ["E0", "I0", "Sigma0", "Delta0"]:
        riga(k, data[k][i, j], raw[k][i, j])

    E0r, I0r = raw["E0"][i, j], raw["I0"][i, j]
    S_E = wEE * E0r - wEI * I0r + h_val
    S_I = wIE * E0r - wII * I0r + h_val
    print(f"  S_E = wEE*E0 - wEI*I0 + h = {S_E: .6e}   ({'> 0: E attivo' if S_E > 0 else '<= 0: f(S_E) = 0'})")
    print(f"  S_I = wIE*E0 - wII*I0 + h = {S_I: .6e}")
    print(f"  controllo punto fisso E: alpha*E0 - (1-E0)*tanh(S_E)^+ = "
          f"{alpha * E0r - (1 - E0r) * np.tanh(max(S_E, 0.0)): .3e}")

    # ---------- matrice di drift ----------
    A_EI_mat = np.array([[data["A_EE"][i, j], data["A_EI"][i, j]],
                         [data["A_IE"][i, j], data["A_II"][i, j]]])
    A_SD_mat = np.array([[data["A_x"][i, j], data["A_y"][i, j]],
                         [data["A_z"][i, j], data["A_w"][i, j]]])

    print("\n--- Matrice di drift ---")
    for k in ["A_EE", "A_EI", "A_IE", "A_II", "A_x", "A_y", "A_z", "A_w"]:
        riga(k, data[k][i, j], raw[k][i, j])
    print(f"  Tr A = {np.trace(A_SD_mat): .6e},  det A = {np.linalg.det(A_SD_mat): .6e}")

    # ---------- covarianza ----------
    print("\n--- Covarianza sigma (base Sigma, Delta) ---")
    for k in ["sigma11", "sigma12", "sigma22"]:
        riga(k, data[k][i, j], raw[k][i, j])
    sig = np.array([[data["sigma11"][i, j], data["sigma12"][i, j]],
                    [data["sigma12"][i, j], data["sigma22"][i, j]]])
    print(f"  autovalori di sigma = {np.linalg.eigvalsh(sig)}")

    # ---------- W ----------
    print("\n--- Produzione di entropia ---")
    delta_term = (np.sqrt(chiE / chiI) * data["A_EI"][i, j] * data["I0"][i, j]
                  - np.sqrt(chiI / chiE) * data["A_IE"][i, j] * data["E0"][i, j])
    riga("delta", delta_term)
    riga("numeratore delta^2", W_num[h_label][i, j])
    riga("denominatore", W_den[h_label][i, j])
    print(f"  W (dati arrotondati)   = {W[i, j]}")

    delta_raw = (np.sqrt(chiE / chiI) * raw["A_EI"][i, j] * raw["I0"][i, j]
                 - np.sqrt(chiI / chiE) * raw["A_IE"][i, j] * raw["E0"][i, j])
    den_raw = (raw["A_EE"][i, j] + raw["A_II"][i, j]) * raw["E0"][i, j] * raw["I0"][i, j]
    with np.errstate(divide="ignore", invalid="ignore"):
        W_raw = -delta_raw**2 / den_raw
    print(f"  W (dati grezzi)        = {W_raw:.6e}")

    # ---------- autovalori ----------
    print("\n--- Autovalori ---")
    print(f"  is_complex (salvato)   = {data['is_complex'][i, j]}")
    for k in ["lambda1", "lambda2", "lambda_re", "lambda_im"]:
        riga(k, data[k][i, j], raw[k][i, j])
    print(f"  eig(A) base (E, I)         = {np.linalg.eigvals(A_EI_mat)}")
    print(f"  eig(A) base (Sigma, Delta) = {np.linalg.eigvals(A_SD_mat)}")
    disc = (A_SD_mat[0, 0] - A_SD_mat[1, 1])**2 + 4 * A_SD_mat[0, 1] * A_SD_mat[1, 0]
    print(f"  discriminante (x-w)^2 + 4yz = {disc: .6e}")

    # ---------- intorno 3x3 ----------
    i0, i1 = max(i - 1, 0), min(i + 2, len(data["delta_EI"]))
    j0, j1 = max(j - 1, 0), min(j + 2, len(data["delta_IE"]))
    print(f"\n--- Intorno 3x3 (righe: delta_EI = {np.round(data['delta_EI'][i0:i1], 2)}, "
          f"colonne: delta_IE = {np.round(data['delta_IE'][j0:j1], 2)}) ---")
    with np.printoptions(precision=3, linewidth=120):
        print("  E0 grezzo:\n", raw["E0"][i0:i1, j0:j1])
        print("  A_EI grezzo:\n", raw["A_EI"][i0:i1, j0:j1])
        print("  W (arrotondato; nan = 0/0):\n", W[i0:i1, j0:j1])


h = 10^{-6}: punti con W = inf trovati: 1

Punto di griglia (i, j) = (71, 69)
  delta_EI = 0.1000  ->  w_EI = w_II + delta_EI = 6.9500
  delta_IE = 0.0000  ->  w_IE = w_EE + delta_IE = 6.9500

--- Stato stazionario ---
  E0                     =  0.000000000000e+00   (grezzo:  3.600413541606e-12)
  I0                     =  1.440000000000e-07   (grezzo:  1.438884924067e-07)
  Sigma0                 =  4.300000000000e-08   (grezzo:  4.316906801148e-08)
  Delta0                 = -4.300000000000e-08   (grezzo: -4.316402743252e-08)
  S_E = wEE*E0 - wEI*I0 + h =  6.476895e-16   (> 0: E attivo)
  S_I = wIE*E0 - wII*I0 + h =  1.438885e-08
  controllo punto fisso E: alpha*E0 - (1-E0)*tanh(S_E)^+ =  3.594e-13

--- Matrice di drift ---
  A_EE                   =  6.850000000000e+00   (grezzo:  6.849999999975e+00)
  A_EI                   = -6.950000000000e+00   (grezzo: -6.949999999975e+00)
  A_IE                   =  6.949999000000e+00   (grezzo:  6.949998999975e+00)
  A_II                   =